In [1]:
import time
import numpy as np
from scipy import signal
from pynq import Overlay, allocate
from rtlsdr import RtlSdr

# ol = Overlay("./../vivado/pynq_fm.bit")
ol = Overlay("./../overlay/base.bit")

In [2]:
# check IP contents in bitstream
print(ol.ip_dict.keys())

dma = ol.axi_dma_0

dict_keys(['axi_dma_0', 'ps7_0'])


/usr/local/share/pynq-venv/lib/python3.8/site-packages/pynq/overlay.py:681: UserWarning: Interrupt s2mm_introut not created: Could not find UIO device for interrupt pin for IRQ number 62
  warnings.warn('Interrupt {} not created: {}'.format(


In [3]:
len_in = 1024 * 1500
len_out = int(len_in / 40)

resize = 1 / 40

In [4]:
# make input buffer and output buffer for AXI DMA
input_buffer = allocate(shape=(len_in,), dtype=np.uint16)
output_buffer = allocate(shape=(len_out,), dtype=np.int16)

print(f"Input Buffer Address: {hex(input_buffer.device_address)}")
print(f"Output Buffer Address: {hex(output_buffer.device_address)}")

Input Buffer Address: 0x16900000
Output Buffer Address: 0x16860000


In [5]:
# connect and configure RTL-SDR
sdr = RtlSdr()

fc = 99750000
fs = 1920000
ppm = 60

sdr.sample_rate = fs
sdr.center_freq = fc
sdr.freq_correction = ppm
sdr.gain = "auto"

In [6]:
# increase usb memory buffer
!echo 0 > /sys/module/usbcore/parameters/usbfs_memory_mb

In [7]:
from IPython.display import Audio
import nest_asyncio
import asyncio

In [8]:
nest_asyncio.apply()

flag = 0

it_num = 100

async def streaming():
    it = 0
    async for data in sdr.stream(num_samples_or_bytes=len_in*2, format='bytes', loop=None):
        global flag
        
        raw_uint8 = np.frombuffer(data, dtype=np.uint8)
        
        raw_int8 = (raw_uint8.astype(np.int16) - 128).astype(np.int8)
        
        packed_samples = raw_int8.view(np.uint16)
        
        np.copyto(input_buffer, packed_samples)
        
        if flag == 1:
            dma.sendchannel.wait()
            dma.recvchannel.wait()
        else:
            flag = 1
            
        dma.sendchannel.transfer(input_buffer)
        dma.recvchannel.transfer(output_buffer)
        
        audio_data = output_buffer.astype(np.float32) / 32768.0
        
        display(Audio(audio_data, autoplay=True, rate=48000, normalize=False))
        
        it = it + 1
        print("sample %d" % it)
        if it == it_num:
            print("Stopping stream...")
            await sdr.stop()
            sdr.close()
            break
        
asyncio.run(streaming())

sample 1


sample 2


sample 3


sample 4


sample 5


...

sample 96


sample 97


sample 98


sample 99


sample 100
Stopping stream...


In [9]:
# delete input buffer and output buffer
del input_buffer, output_buffer